In [ ]:
import os
#from google.colab import drive
#drive.mount('/content/drive')
#os.chdir('/content/drive/MyDrive/FSE 570/Raw Data')

In [ ]:
from alpaca.data.historical import StockHistoricalDataClient
from alpaca.data.requests import StockBarsRequest
from alpaca.data.timeframe import TimeFrame

print("Imports successful!")

Imports successful!


In [ ]:
import requests
import pandas as pd
import geopandas as gpd
import numpy as np
from shapely.geometry import Point
from IPython.display import Markdown, display

### CENSUS DATA

url = "https://api.census.gov/data/2023/acs/acs5"
params = {
    "get": "B01001_001E,B19013_001E,B01002_001E,B16009_002E,B06009_025E",
    "for": "zip code tabulation area:60601,60602,60603,60604,60605,60606,60607,60608,60609,60610,60611,60612,60613,60614,60615,60616,60617,60618,60619,60620,60621,60622,60623,60624,60625,60626,60628,60629,60630,60631,60632,60633,60634,60636,60637,60638,60639,60640,60641,60642,60643,60644,60645,60646,60647,60649,60651,60652,60653,60654,60655,60656,60657,60659,60660,60661,60701,60706,60803,60804,60805,60827"
}
response = requests.get(url, params=params)
response.raise_for_status()


data = response.json()
zcta = pd.DataFrame(data[1:], columns=["population", "median_income", "median_age","population_below_poverty_level","foreign_born_pop","zip_code"])
zcta["population"] = zcta["population"].astype(int)
zcta["median_income"] = zcta["median_income"].astype(int)
zcta["median_age"] = zcta["median_age"].astype(float)
zcta["population_below_poverty_level"] = zcta["population_below_poverty_level"].astype(int)
zcta["foreign_born_pop"] = zcta["foreign_born_pop"].astype(int)

zcta = zcta[[zcta.columns[-1]] + list(zcta.columns[:-1])]

census_data = zcta
census_data['poverty_rate'] = (census_data['population_below_poverty_level'] / census_data['population']).round(4)
census_data['foreign_rate'] = (census_data['foreign_born_pop'] / census_data['population']).round(4)
census_data = census_data.drop(columns=['population_below_poverty_level','foreign_born_pop'])
census_data
df_census = census_data
df_census



,zip_code,population,median_income,median_age,poverty_rate,foreign_rate
0,60601,16292,127323,33.5,0.0564,0.3010
1,60602,1127,123047,30.3,0.0186,0.3256
2,60603,1126,128107,33.9,0.1297,0.2336
3,60604,653,77806,40.6,0.1700,0.2052
4,60605,34256,118403,31.7,0.0770,0.2082
...,...,...,...,...,...,...
56,60706,24028,85000,45.0,0.0536,0.3875
57,60803,22089,66555,39.4,0.0989,0.1002
58,60804,83223,68548,34.3,0.1216,0.3729
59,60805,19498,95738,38.1,0.0419,0.0917


In [ ]:
### CRASHES DATA

df_crashes=pd.read_csv("Traffic_Crashes_-_Crashes_20251007.csv")

display(df_crashes.head())
df_crashes.info()
display(df_crashes.describe())
missing_percentages = df_crashes.isnull().sum() / len(df_crashes) * 100
display(missing_percentages)

# Identify columns with more than 50% missing values
missing_percentages = df_crashes.isnull().sum() / len(df_crashes) * 100 # Recalculate missing percentages for this cell
high_missing_columns = missing_percentages[missing_percentages > 90].index.tolist()
print("Columns with more than 50% missing values:")
print(high_missing_columns)

# Drop columns with more than 50% missing values
df_crashes_cleaned = df_crashes.drop(columns=high_missing_columns, inplace=False)
print(f"\nDropped columns: {high_missing_columns}")
print(f"Shape of DataFrame after dropping columns: {df_crashes_cleaned.shape}")

print("\nUnique values in some object columns (after dropping high missing value columns):")
object_cols_cleaned = df_crashes_cleaned.select_dtypes(include='object').columns

# These columns were chosen for initial inspection because they represent key factors
# commonly analyzed in traffic crash studies (environmental conditions, roadway features,
# and contributing factors) and are directly relevant to the project objectives.
cols_to_inspect = ['TRAFFIC_CONTROL_DEVICE', 'WEATHER_CONDITION', 'LIGHTING_CONDITION', 'FIRST_CRASH_TYPE', 'ROADWAY_SURFACE_COND', 'ROAD_DEFECT', 'PRIM_CONTRIBUTORY_CAUSE', 'SEC_CONTRIBUTORY_CAUSE']

for col in cols_to_inspect:
    if col in object_cols_cleaned: # Check against columns in the cleaned DataFrame
        print(f"\n--- {col} ---")
        # Use df_crashes_cleaned here as df_crashes_cleaned is the relevant dataframe now
        print(df_crashes_cleaned[col].unique()[:10]) # Displaying only first 10 unique values for brevity
    else:
        print(f"\n--- {col} not in cleaned DataFrame ---") # In case a requested column was dropped

# Identify columns with missing values in the cleaned DataFrame
missing_percentages_cleaned = df_crashes_cleaned.isnull().sum() / len(df_crashes_cleaned) * 100
print("Missing percentages in df_crashes_cleaned:")
display(missing_percentages_cleaned)



C:\Users\dgdgi\AppData\Local\Temp\ipykernel_36996\3454132452.py:3: DtypeWarning: Columns (10) have mixed types. Specify dtype option on import or set low_memory=False.
  df_crashes=pd.read_csv("Traffic_Crashes_-_Crashes_20251007.csv")


,CRASH_RECORD_ID,CRASH_DATE_EST_I,CRASH_DATE,POSTED_SPEED_LIMIT,TRAFFIC_CONTROL_DEVICE,DEVICE_CONDITION,WEATHER_CONDITION,LIGHTING_CONDITION,FIRST_CRASH_TYPE,TRAFFICWAY_TYPE,...,INJURIES_NON_INCAPACITATING,INJURIES_REPORTED_NOT_EVIDENT,INJURIES_NO_INDICATION,INJURIES_UNKNOWN,CRASH_HOUR,CRASH_DAY_OF_WEEK,CRASH_MONTH,LATITUDE,LONGITUDE,LOCATION
0,c26b67cd2da9fbc8be3a8d4b83b147e69c3b031d0abc2c...,NaN,10/07/2025 01:28:00 AM,30,TRAFFIC SIGNAL,FUNCTIONING PROPERLY,RAIN,"DARKNESS, LIGHTED ROAD",REAR TO FRONT,FOUR WAY,...,0.0,0.0,2.0,0.0,1,3,10,41.968643,-87.698492,POINT (-87.698491722355 41.968643044359)
1,7b0eb093a1800b3487b8b7d18362dbad3467f61e320ee9...,NaN,10/07/2025 01:05:00 AM,30,NO CONTROLS,NO CONTROLS,OTHER,"DARKNESS, LIGHTED ROAD",PARKED MOTOR VEHICLE,NOT DIVIDED,...,0.0,0.0,1.0,0.0,1,3,10,41.826667,-87.689679,POINT (-87.689678969045 41.826666608837)
2,66c8fb7ca043fb91fa194c4c82acb20b8a54fc3e478deb...,NaN,10/07/2025 12:47:00 AM,25,STOP SIGN/FLASHER,UNKNOWN,RAIN,"DARKNESS, LIGHTED ROAD",FIXED OBJECT,T-INTERSECTION,...,0.0,0.0,2.0,0.0,0,3,10,41.885533,-87.759074,POINT (-87.759073957098 41.885532532443)
3,543b08b85ce5854c761d4def4fcbf0602f55e0cfdd991c...,NaN,10/07/2025 12:45:00 AM,25,NO CONTROLS,NO CONTROLS,CLEAR,"DARKNESS, LIGHTED ROAD",PARKED MOTOR VEHICLE,ONE-WAY,...,1.0,0.0,0.0,0.0,0,3,10,41.823030,-87.621437,POINT (-87.621437387284 41.823029573152)
4,afd384a0563e4639e61ca9d13f3036f91b1fb16268e466...,Y,10/06/2025 11:48:00 PM,35,NO CONTROLS,NO CONTROLS,CLEAR,DARKNESS,SIDESWIPE SAME DIRECTION,NOT DIVIDED,...,0.0,0.0,2.0,0.0,23,2,10,41.828208,-87.670489,POINT (-87.670488777376 41.828207872994)


<class 'pandas.core.frame.DataFrame'>
RangeIndex: 991122 entries, 0 to 991121
Data columns (total 48 columns):
 #   Column                         Non-Null Count   Dtype  
---  ------                         --------------   -----  
 0   CRASH_RECORD_ID                991122 non-null  object 
 1   CRASH_DATE_EST_I               72116 non-null   object 
 2   CRASH_DATE                     991122 non-null  object 
 3   POSTED_SPEED_LIMIT             991122 non-null  int64  
 4   TRAFFIC_CONTROL_DEVICE         991122 non-null  object 
 5   DEVICE_CONDITION               991122 non-null  object 
 6   WEATHER_CONDITION              991122 non-null  object 
 7   LIGHTING_CONDITION             991122 non-null  object 
 8   FIRST_CRASH_TYPE               991122 non-null  object 
 9   TRAFFICWAY_TYPE                991122 non-null  object 
 10  LANE_CNT                       199029 non-null  object 
 11  ALIGNMENT                      991122 non-null  object 
 12  ROADWAY_SURFACE_COND          

,POSTED_SPEED_LIMIT,STREET_NO,BEAT_OF_OCCURRENCE,NUM_UNITS,INJURIES_TOTAL,INJURIES_FATAL,INJURIES_INCAPACITATING,INJURIES_NON_INCAPACITATING,INJURIES_REPORTED_NOT_EVIDENT,INJURIES_NO_INDICATION,INJURIES_UNKNOWN,CRASH_HOUR,CRASH_DAY_OF_WEEK,CRASH_MONTH,LATITUDE,LONGITUDE
count,991122.000000,991122.000000,991117.000000,991122.000000,988974.000000,988974.000000,988974.000000,988974.000000,988974.000000,988974.000000,988974.0,991122.000000,991122.000000,991122.000000,983657.000000,983657.000000
mean,28.422960,3685.994177,1247.529812,2.035158,0.197525,0.001151,0.019352,0.109822,0.067200,1.997680,0.0,13.195362,4.119648,6.640287,41.855208,-87.673235
std,6.058294,2873.086021,704.696189,0.449698,0.577210,0.036819,0.162816,0.426650,0.334241,1.155668,0.0,5.572807,1.979833,3.362295,0.350989,0.715154
min,0.000000,0.000000,111.000000,1.000000,0.000000,0.000000,0.000000,0.000000,0.000000,0.000000,0.0,0.000000,1.000000,1.000000,0.000000,-87.939678
25%,30.000000,1256.000000,722.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,1.000000,0.0,9.000000,2.000000,4.000000,41.783981,-87.721790
50%,30.000000,3201.000000,1213.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,2.000000,0.0,14.000000,4.000000,7.000000,41.875155,-87.674359
75%,30.000000,5555.000000,1822.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,2.000000,0.0,17.000000,6.000000,9.000000,41.924757,-87.633777
max,99.000000,451100.000000,6100.000000,18.000000,21.000000,4.000000,10.000000,21.000000,19.000000,61.000000,0.0,23.000000,7.000000,12.000000,42.022780,0.000000


CRASH_RECORD_ID                   0.000000
CRASH_DATE_EST_I                 92.723802
CRASH_DATE                        0.000000
POSTED_SPEED_LIMIT                0.000000
TRAFFIC_CONTROL_DEVICE            0.000000
DEVICE_CONDITION                  0.000000
WEATHER_CONDITION                 0.000000
LIGHTING_CONDITION                0.000000
FIRST_CRASH_TYPE                  0.000000
TRAFFICWAY_TYPE                   0.000000
LANE_CNT                         79.918819
ALIGNMENT                         0.000000
ROADWAY_SURFACE_COND              0.000000
ROAD_DEFECT                       0.000000
REPORT_TYPE                       3.284762
CRASH_TYPE                        0.000000
INTERSECTION_RELATED_I           77.020286
NOT_RIGHT_OF_WAY_I               95.499343
HIT_AND_RUN_I                    68.625961
DAMAGE                            0.000000
DATE_POLICE_NOTIFIED              0.000000
PRIM_CONTRIBUTORY_CAUSE           0.000000
SEC_CONTRIBUTORY_CAUSE            0.000000
STREET_NO  

Columns with more than 50% missing values:
['CRASH_DATE_EST_I', 'NOT_RIGHT_OF_WAY_I', 'PHOTOS_TAKEN_I', 'STATEMENTS_TAKEN_I', 'DOORING_I', 'WORK_ZONE_I', 'WORK_ZONE_TYPE', 'WORKERS_PRESENT_I']

Dropped columns: ['CRASH_DATE_EST_I', 'NOT_RIGHT_OF_WAY_I', 'PHOTOS_TAKEN_I', 'STATEMENTS_TAKEN_I', 'DOORING_I', 'WORK_ZONE_I', 'WORK_ZONE_TYPE', 'WORKERS_PRESENT_I']
Shape of DataFrame after dropping columns: (991122, 40)

Unique values in some object columns (after dropping high missing value columns):

--- TRAFFIC_CONTROL_DEVICE ---
['TRAFFIC SIGNAL' 'NO CONTROLS' 'STOP SIGN/FLASHER' 'UNKNOWN'
 'FLASHING CONTROL SIGNAL' 'OTHER' 'YIELD' 'PEDESTRIAN CROSSING SIGN'
 'OTHER REG. SIGN' 'OTHER WARNING SIGN']

--- WEATHER_CONDITION ---
['RAIN' 'OTHER' 'CLEAR' 'UNKNOWN' 'CLOUDY/OVERCAST'
 'FREEZING RAIN/DRIZZLE' 'SNOW' 'FOG/SMOKE/HAZE' 'SEVERE CROSS WIND GATE'
 'BLOWING SNOW']

--- LIGHTING_CONDITION ---
['DARKNESS, LIGHTED ROAD' 'DARKNESS' 'UNKNOWN' 'DUSK' 'DAWN' 'DAYLIGHT']

--- FIRST_CRASH_TYPE --

CRASH_RECORD_ID                   0.000000
CRASH_DATE                        0.000000
POSTED_SPEED_LIMIT                0.000000
TRAFFIC_CONTROL_DEVICE            0.000000
DEVICE_CONDITION                  0.000000
WEATHER_CONDITION                 0.000000
LIGHTING_CONDITION                0.000000
FIRST_CRASH_TYPE                  0.000000
TRAFFICWAY_TYPE                   0.000000
LANE_CNT                         79.918819
ALIGNMENT                         0.000000
ROADWAY_SURFACE_COND              0.000000
ROAD_DEFECT                       0.000000
REPORT_TYPE                       3.284762
CRASH_TYPE                        0.000000
INTERSECTION_RELATED_I           77.020286
HIT_AND_RUN_I                    68.625961
DAMAGE                            0.000000
DATE_POLICE_NOTIFIED              0.000000
PRIM_CONTRIBUTORY_CAUSE           0.000000
SEC_CONTRIBUTORY_CAUSE            0.000000
STREET_NO                         0.000000
STREET_DIRECTION                  0.000404
STREET_NAME

In [ ]:
# --- Strategy for handling missing values in remaining columns ---

# 1. Handle missing values in 'REPORT_TYPE' (~3.28% missing)
# This is a categorical column. Dropping rows with missing 'REPORT_TYPE' as importance is moderate.
df_crashes_cleaned.dropna(subset=['REPORT_TYPE'], inplace=True)
print("\nDropped rows with missing REPORT_TYPE.")

# 2. Handle missing values in location-related columns ('LATITUDE', 'LONGITUDE', 'LOCATION') (~0.75% missing)
# These are critical for location-based analysis. Given the low percentage and importance, dropping rows is reasonable.
df_crashes_cleaned.dropna(subset=['LATITUDE', 'LONGITUDE', 'LOCATION'], inplace=True)
print("Dropped rows with missing LATITUDE, LONGITUDE, or LOCATION.")

# 3. Handle missing values in injury-related columns (~0.22% missing)
# These are numerical injury counts. Given the low percentage, dropping rows is also reasonable.
df_crashes_cleaned.dropna(subset=[
    'MOST_SEVERE_INJURY',
    'INJURIES_TOTAL',
    'INJURIES_FATAL',
    'INJURIES_INCAPACITATING',
    'INJURIES_NON_INCAPACITATING',
    'INJURIES_REPORTED_NOT_EVIDENT',
    'INJURIES_NO_INDICATION'
], inplace=True)
print("Dropped rows with missing injury data.")

# 4. Handle missing values in 'STREET_DIRECTION' (~0.0004% missing)
# Very low percentage. Dropping rows is appropriate.
df_crashes_cleaned.dropna(subset=['STREET_DIRECTION'], inplace=True)
print("Dropped rows with missing STREET_DIRECTION.")

# 5. Handle missing values in 'BEAT_OF_OCCURRENCE' (~0.0005% missing)
# Very low percentage. Dropping rows is appropriate.
df_crashes_cleaned.dropna(subset=['BEAT_OF_OCCURRENCE'], inplace=True)
print("Dropped rows with missing BEAT_OF_OCCURRENCE.")

# 6. Handle missing values in 'STREET_NAME' (~0.0001% missing)
# Very low percentage. Dropping rows is appropriate.
df_crashes_cleaned.dropna(subset=['STREET_NAME'], inplace=True)
print("Dropped rows with missing STREET_NAME.")


# --- Address inconsistencies and outliers ---

# Handle categorical inconsistencies:
# Based on value counts, no obvious spelling or capitalization inconsistencies observed earlier.
# 'UNKNOWN' and 'OTHER' categories are present and will be kept as they represent valid (though unspecific) conditions.

# Handle numerical outliers:
# POSTED_SPEED_LIMIT: 0 is present. Replace 0 with the mode (30) because it's a discrete variable.
if (df_crashes_cleaned['POSTED_SPEED_LIMIT'] == 0).any():
    mode_speed_limit = df_crashes_cleaned['POSTED_SPEED_LIMIT'].mode()[0]
    df_crashes_cleaned['POSTED_SPEED_LIMIT'] = df_crashes_cleaned['POSTED_SPEED_LIMIT'].replace(0, mode_speed_limit)
    print(f"\nReplaced 0 in POSTED_SPEED_LIMIT with mode ({mode_speed_limit}).")


# LATITUDE and LONGITUDE: 0.0 values are present. These are clearly incorrect coordinates.
# Since we already dropped rows with missing LATITUDE/LONGITUDE, these 0.0 values might have been handled.
# Re-check and drop rows where LATITUDE or LONGITUDE are 0.0 if any remain.
# print('count of rows with 0 lat and long',df_cleaned[(df_cleaned['LATITUDE'] == 0.0) & (df_cleaned['LONGITUDE'] == 0.0)].shape[0])
if ((df_crashes_cleaned['LATITUDE'] == 0.0) | (df_crashes_cleaned['LONGITUDE'] == 0.0)).any():
     initial_shape = df_crashes_cleaned.shape[0]
     df_crashes_cleaned = df_crashes_cleaned[(df_crashes_cleaned['LATITUDE'] != 0.0) & (df_crashes_cleaned['LONGITUDE'] != 0.0)].copy()
     dropped_count = initial_shape - df_crashes_cleaned.shape[0]
     print(f"Dropped {dropped_count} rows with LATITUDE or LONGITUDE equal to 0.0.")


# INJURIES_UNKNOWN: All values were 0.0 in the initial data. This column provides no information and can be dropped.
if 'INJURIES_UNKNOWN' in df_crashes_cleaned.columns:
    df_crashes_cleaned = df_crashes_cleaned.drop('INJURIES_UNKNOWN', axis=1).copy()
    print("\nDropped INJURIES_UNKNOWN column.")

### LANE COUNT, HIT AND RUN, INTERSECTION RELATED

df_crashes_cleaned['HIT_AND_RUN_I'] = df_crashes_cleaned['HIT_AND_RUN_I'].fillna('N')        # fill NaN
df_crashes_cleaned['HIT_AND_RUN_I'] = df_crashes_cleaned['HIT_AND_RUN_I'].replace('', 'N')   # fill empty strings
df_crashes_cleaned['INTERSECTION_RELATED_I'] = df_crashes_cleaned['INTERSECTION_RELATED_I'].fillna('N')        # fill NaN
df_crashes_cleaned['INTERSECTION_RELATED_I'] = df_crashes_cleaned['INTERSECTION_RELATED_I'].replace('', 'N')   # fill empty strings

# 2️⃣ Convert Y/N to 1/0
df_crashes_cleaned['HIT_AND_RUN_I'] = df_crashes_cleaned['HIT_AND_RUN_I'].map({'Y': 1, 'N': 0})
df_crashes_cleaned['INTERSECTION_RELATED_I'] = df_crashes_cleaned['INTERSECTION_RELATED_I'].map({'Y': 1, 'N': 0})
df_crashes_cleaned.drop(columns = ['LANE_CNT'], inplace=True)


Dropped rows with missing REPORT_TYPE.
Dropped rows with missing LATITUDE, LONGITUDE, or LOCATION.
Dropped rows with missing injury data.
Dropped rows with missing STREET_DIRECTION.
Dropped rows with missing BEAT_OF_OCCURRENCE.
Dropped rows with missing STREET_NAME.

Replaced 0 in POSTED_SPEED_LIMIT with mode (30).
Dropped 60 rows with LATITUDE or LONGITUDE equal to 0.0.

Dropped INJURIES_UNKNOWN column.


In [ ]:
# Verify missing values after cleaning for all remaining columns
missing_percentages_cleaned_final = df_crashes_cleaned.isnull().sum() / len(df_crashes_cleaned) * 100
print("\nMissing percentages after handling missing values and inconsistencies:")
display(missing_percentages_cleaned_final)

print("\nShape of the DataFrame after cleaning:", df_crashes_cleaned.shape)

# Get the initial shape from the original DataFrame (df)
initial_rows, initial_cols = df_crashes.shape

# Get the final shape from the cleaned DataFrame (df_cleaned)
final_rows, final_cols = df_crashes_cleaned.shape

# Calculate the number of removed rows and columns
removed_rows = initial_rows - final_rows
removed_cols = initial_cols - final_cols

# Calculate the percentage of removed rows and columns
percentage_removed_rows = (removed_rows / initial_rows) * 100
percentage_removed_cols = (removed_cols / initial_cols) * 100

print(f"Initial shape of the DataFrame: ({initial_rows} rows, {initial_cols} columns)")
print(f"Final shape of the DataFrame after cleaning: ({final_rows} rows, {final_cols} columns)")
print(f"\nNumber of rows removed: {removed_rows} ({percentage_removed_rows:.2f}%)")
print(f"Number of columns removed: {removed_cols} ({percentage_removed_cols:.2f}%)")

# display descriptive statistics again on the cleaned data
print("\nDescriptive statistics on cleaned DataFrame:")
display(df_crashes_cleaned.describe())

# Convert 'CRASH_DATE','DATE_POLICE_NOTIFIED' to datetime objects
# Use errors='coerce' to turn any unparseable dates into NaT (Not a Time)
df_crashes_cleaned['CRASH_DATE'] = pd.to_datetime(df_crashes_cleaned['CRASH_DATE'], errors='coerce')
df_crashes_cleaned['DATE_POLICE_NOTIFIED'] = pd.to_datetime(df_crashes_cleaned['DATE_POLICE_NOTIFIED'], errors='coerce')
# Verify the data type
print("Data type of 'CRASH_DATE','DATE_POLICE_NOTIFIED' after conversion:")
print(df_crashes_cleaned['CRASH_DATE'].dtype,df_crashes_cleaned['DATE_POLICE_NOTIFIED'].dtype)

# Check for any NaT values introduced by coercion (should be none if missing values were handled for this column)
print(f"\nNumber of NaT values in 'CRASH_DATE': {df_crashes_cleaned['CRASH_DATE'].isnull().sum()}, 'DATE_POLICE_NOTIFIED': {df_crashes_cleaned['DATE_POLICE_NOTIFIED'].isnull().sum()}")


# Additionally, check other columns that might need type conversion if necessary
print("\nData types of df_cleaned after date conversion:")
display(df_crashes_cleaned.info())




Missing percentages after handling missing values and inconsistencies:


CRASH_RECORD_ID                  0.0
CRASH_DATE                       0.0
POSTED_SPEED_LIMIT               0.0
TRAFFIC_CONTROL_DEVICE           0.0
DEVICE_CONDITION                 0.0
WEATHER_CONDITION                0.0
LIGHTING_CONDITION               0.0
FIRST_CRASH_TYPE                 0.0
TRAFFICWAY_TYPE                  0.0
ALIGNMENT                        0.0
ROADWAY_SURFACE_COND             0.0
ROAD_DEFECT                      0.0
REPORT_TYPE                      0.0
CRASH_TYPE                       0.0
INTERSECTION_RELATED_I           0.0
HIT_AND_RUN_I                    0.0
DAMAGE                           0.0
DATE_POLICE_NOTIFIED             0.0
PRIM_CONTRIBUTORY_CAUSE          0.0
SEC_CONTRIBUTORY_CAUSE           0.0
STREET_NO                        0.0
STREET_DIRECTION                 0.0
STREET_NAME                      0.0
BEAT_OF_OCCURRENCE               0.0
NUM_UNITS                        0.0
MOST_SEVERE_INJURY               0.0
INJURIES_TOTAL                   0.0
I


Shape of the DataFrame after cleaning: (949110, 38)
Initial shape of the DataFrame: (991122 rows, 48 columns)
Final shape of the DataFrame after cleaning: (949110 rows, 38 columns)

Number of rows removed: 42012 (4.24%)
Number of columns removed: 10 (20.83%)

Descriptive statistics on cleaned DataFrame:


,POSTED_SPEED_LIMIT,INTERSECTION_RELATED_I,HIT_AND_RUN_I,STREET_NO,BEAT_OF_OCCURRENCE,NUM_UNITS,INJURIES_TOTAL,INJURIES_FATAL,INJURIES_INCAPACITATING,INJURIES_NON_INCAPACITATING,INJURIES_REPORTED_NOT_EVIDENT,INJURIES_NO_INDICATION,CRASH_HOUR,CRASH_DAY_OF_WEEK,CRASH_MONTH,LATITUDE,LONGITUDE
count,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000,949110.000000
mean,28.667532,0.217849,0.300618,3691.877906,1247.529633,2.031533,0.190717,0.000911,0.018430,0.106144,0.065232,1.995203,13.200887,4.121303,6.644268,41.858106,-87.679073
std,5.471889,0.412785,0.458527,2828.471464,705.076476,0.438442,0.563983,0.032689,0.157974,0.417572,0.328113,1.153324,5.555693,1.977896,3.362754,0.086163,0.059010
min,1.000000,0.000000,0.000000,1.000000,111.000000,1.000000,0.000000,0.000000,0.000000,0.000000,0.000000,0.000000,0.000000,1.000000,1.000000,41.644613,-87.939678
25%,30.000000,0.000000,0.000000,1300.000000,722.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,1.000000,9.000000,2.000000,4.000000,41.784207,-87.721786
50%,30.000000,0.000000,0.000000,3202.000000,1212.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,2.000000,14.000000,4.000000,7.000000,41.875223,-87.674412
75%,30.000000,0.000000,1.000000,5555.000000,1822.000000,2.000000,0.000000,0.000000,0.000000,0.000000,0.000000,2.000000,17.000000,6.000000,9.000000,41.924839,-87.633827
max,99.000000,1.000000,1.000000,13799.000000,2535.000000,18.000000,21.000000,4.000000,10.000000,21.000000,19.000000,61.000000,23.000000,7.000000,12.000000,42.022780,-87.524587


Data type of 'CRASH_DATE','DATE_POLICE_NOTIFIED' after conversion:
datetime64[ns] datetime64[ns]

Number of NaT values in 'CRASH_DATE': 0, 'DATE_POLICE_NOTIFIED': 0

Data types of df_cleaned after date conversion:
<class 'pandas.core.frame.DataFrame'>
Index: 949110 entries, 0 to 991121
Data columns (total 38 columns):
 #   Column                         Non-Null Count   Dtype         
---  ------                         --------------   -----         
 0   CRASH_RECORD_ID                949110 non-null  object        
 1   CRASH_DATE                     949110 non-null  datetime64[ns]
 2   POSTED_SPEED_LIMIT             949110 non-null  int64         
 3   TRAFFIC_CONTROL_DEVICE         949110 non-null  object        
 4   DEVICE_CONDITION               949110 non-null  object        
 5   WEATHER_CONDITION              949110 non-null  object        
 6   LIGHTING_CONDITION             949110 non-null  object        
 7   FIRST_CRASH_TYPE               949110 non-null  object        


None

In [ ]:
os.listdir()


['Boundaries - ZIP Codes_20251007',
 'FSE570_Master.ipynb',
 'Red_Light_Camera_Locations_20251007.csv',
 'Red_Light_Camera_Violations_20251007.csv',
 'Speed_Camera_Locations_20251007.csv',
 'Speed_Camera_Violations_20251007.csv',
 'Traffic_Crashes_-_Crashes_20251007.csv',
 'Traffic_Crashes_-_People_20251007.csv',
 'Traffic_Crashes_-_Vehicles_20251007.csv']

In [ ]:
import geopandas as gpd
from shapely.geometry import Point

# Define the path to the Chicago zipcode shapefile components
shapefile_path = 'Boundaries - ZIP Codes_20251007/geo_export_60181f98-0954-4967-b566-ef3caca5ba08.shp'

# Check if the shapefile components exist
required_extensions = ['.shp', '.shx', '.dbf', '.prj']
files_exist = all(os.path.exists(shapefile_path.replace('.shp', ext)) for ext in required_extensions)

if files_exist:
    try:
        # Attempt to load the zipcode shapefile into a GeoDataFrame
        # Set SHAPE_RESTORE_SHX config option to YES to potentially handle missing/corrupted shx
        # Also specify the CRS if known, assuming EPSG:4326 based on crash data context
        print(f"Attempting to load shapefile from {shapefile_path}...")
        # Setting environment variable might not be sufficient in Colab,
        # will rely on geopandas/fiona's ability to handle missing shx with the flag set if needed.
        # Direct open options are not easily passed via gpd.read_file for this specific flag.
        # Let's try loading without explicit CRS first and reproject if necessary based on crashes_gdf.crs

        zipcode_gdf = gpd.read_file(shapefile_path)
        print("Zipcode shapefile loaded successfully.")
        print("Zipcode GeoDataFrame columns:", zipcode_gdf.columns)
        print("Zipcode GeoDataFrame CRS:", zipcode_gdf.crs)


        # Create a GeoDataFrame from the df_crashes_cleaned DataFrame
        # Ensure LATITUDE and LONGITUDE are not null and are numeric
        df_geo = df_crashes_cleaned.dropna(subset=['LATITUDE', 'LONGITUDE']).copy()
        # Convert LATITUDE and LONGITUDE to numeric, coercing errors
        df_geo['LATITUDE'] = pd.to_numeric(df_geo['LATITUDE'], errors='coerce')
        df_geo['LONGITUDE'] = pd.to_numeric(df_geo['LONGITUDE'], errors='coerce')
        # Drop rows where conversion to numeric resulted in NaNs
        df_geo.dropna(subset=['LATITUDE', 'LONGITUDE'], inplace=True)

        df_geo['geometry'] = df_geo.apply(lambda row: Point(row['LONGITUDE'], row['LATITUDE']), axis=1)
        crashes_gdf = gpd.GeoDataFrame(df_geo, geometry='geometry', crs='EPSG:4326')
        print("\nCrashes GeoDataFrame created successfully.")
        print("Crashes GeoDataFrame shape:", crashes_gdf.shape)
        print("Crashes GeoDataFrame CRS:", crashes_gdf.crs)

        # Ensure the CRS of both GeoDataFrames match for spatial join
        if zipcode_gdf.crs is None and crashes_gdf.crs is not None:
             print("Zipcode GeoDataFrame has no CRS. Assigning crashes_gdf CRS...")
             zipcode_gdf.crs = crashes_gdf.crs
             print("Assigned CRS to zipcode_gdf.")
        elif crashes_gdf.crs != zipcode_gdf.crs and crashes_gdf.crs is not None and zipcode_gdf.crs is not None:
             print(f"\nCRS mismatch: Crashes CRS is {crashes_gdf.crs}, Zipcode CRS is {zipcode_gdf.crs}. Reprojecting crashes_gdf...")
             crashes_gdf = crashes_gdf.to_crs(zipcode_gdf.crs)
             print("Crashes GeoDataFrame reprojected.")


        # Perform a spatial join
        print("\nPerforming spatial join...")
        # Identify the zipcode column name in the shapefile (based on previous inspection, it's likely 'zip')
        zipcode_column_name = None
        for col in zipcode_gdf.columns:
            if 'zip' in col.lower():
                zipcode_column_name = col
                break
        if zipcode_column_name is None:
             if 'ZIPCODE' in zipcode_gdf.columns:
                 zipcode_column_name = 'ZIPCODE'
             elif 'zip' in zipcode_gdf.columns:
                 zipcode_column_name = 'zip'
             else:
                 print("Could not find a likely zipcode column in the shapefile. Spatial join will not add zipcode.")
                 zipcode_column_name = 'unknown_zip_column' # Placeholder

        if zipcode_column_name != 'unknown_zip_column' and zipcode_column_name in zipcode_gdf.columns:
            # Select only the identified zipcode column and geometry from the zipcode_gdf for the join
            columns_for_join = [zipcode_column_name, 'geometry']

            crashes_with_zipcode_gdf = gpd.sjoin(crashes_gdf, zipcode_gdf[columns_for_join], how="left", predicate="within")
            print("Spatial join completed.")
            print("Resulting GeoDataFrame shape:", crashes_with_zipcode_gdf.shape)

            # Add the new zipcode column to the original df_cleaned DataFrame
            # The spatial join adds columns from the right GeoDataFrame (zipcode_gdf) and an 'index_right' column
            # The zipcode information is in the column named by `zipcode_column_name` in the joined GeoDataFrame
            if zipcode_column_name in crashes_with_zipcode_gdf.columns:
                 df_crashes_cleaned['zipcode'] = crashes_with_zipcode_gdf[zipcode_column_name]
                 print(f"\n'{zipcode_column_name}' column from shapefile added as 'zipcode' column to df_cleaned.")
            else:
                 print(f"\nCould not find '{zipcode_column_name}' in the joined GeoDataFrame. Zipcode column not added.")
                 # If the column wasn't in the result, maybe the join failed or the column name was wrong.
                 # We can inspect crashes_with_zipcode_gdf.columns here if needed for debugging.


            # Display the first few rows with the new zipcode column
            print("\nFirst 5 rows of df_cleaned with the new 'zipcode' column:")
            display(df_crashes_cleaned.head())

            # Verify the new column and its data type
            print("\nInfo about df_cleaned after adding zipcode column:")
            df_crashes_cleaned.info()

            # Check how many rows have a zipcode assigned (not null)
            print(f"\nNumber of rows with assigned zipcode: {df_crashes_cleaned['zipcode'].notnull().sum()}")
            print(f"Number of rows without assigned zipcode (outside any polygon): {df_crashes_cleaned['zipcode'].isnull().sum()}")

        else:
            print("Skipping spatial join and zipcode column addition as zipcode column was not identified or found in shapefile.")
            # Keep df_cleaned as is
            print("df_cleaned remains without a zipcode column.")


    except Exception as e:
        print(f"\nError during shapefile loading or spatial join: {e}")
        # If any error occurs, keep df_cleaned as is and report the error
        print("df_cleaned remains without a zipcode column due to the error.")

else:
    print(f"Required shapefile components not found at {shapefile_path}. Cannot perform spatial join.")
    # Keep df_cleaned as is
    print("df_cleaned remains without a zipcode column.")

# Assign the modified DataFrame back to df_cleaned if needed, but the operations above modify it directly (except for the copy when creating df_geo)

df_crashes_cleaned[df_crashes_cleaned['zipcode'].isnull()]

# Drop the 'LOCATION' column
df_crashes_cleaned = df_crashes_cleaned.drop(columns=['LOCATION'], inplace=False)
print("Dropped the 'LOCATION' column.")
print("Shape of DataFrame after dropping 'LOCATION':", df_crashes_cleaned.shape)




Attempting to load shapefile from Boundaries - ZIP Codes_20251007/geo_export_60181f98-0954-4967-b566-ef3caca5ba08.shp...
Zipcode shapefile loaded successfully.
Zipcode GeoDataFrame columns: Index(['objectid', 'zip', 'shape_area', 'shape_len', 'geometry'], dtype='object')
Zipcode GeoDataFrame CRS: EPSG:4326

Crashes GeoDataFrame created successfully.
Crashes GeoDataFrame shape: (949110, 39)
Crashes GeoDataFrame CRS: EPSG:4326

Performing spatial join...
Spatial join completed.
Resulting GeoDataFrame shape: (949110, 41)

'zip' column from shapefile added as 'zipcode' column to df_cleaned.

First 5 rows of df_cleaned with the new 'zipcode' column:


,CRASH_RECORD_ID,CRASH_DATE,POSTED_SPEED_LIMIT,TRAFFIC_CONTROL_DEVICE,DEVICE_CONDITION,WEATHER_CONDITION,LIGHTING_CONDITION,FIRST_CRASH_TYPE,TRAFFICWAY_TYPE,ALIGNMENT,...,INJURIES_NON_INCAPACITATING,INJURIES_REPORTED_NOT_EVIDENT,INJURIES_NO_INDICATION,CRASH_HOUR,CRASH_DAY_OF_WEEK,CRASH_MONTH,LATITUDE,LONGITUDE,LOCATION,zipcode
0,c26b67cd2da9fbc8be3a8d4b83b147e69c3b031d0abc2c...,2025-10-07 01:28:00,30,TRAFFIC SIGNAL,FUNCTIONING PROPERLY,RAIN,"DARKNESS, LIGHTED ROAD",REAR TO FRONT,FOUR WAY,STRAIGHT AND LEVEL,...,0.0,0.0,2.0,1,3,10,41.968643,-87.698492,POINT (-87.698491722355 41.968643044359),60625
1,7b0eb093a1800b3487b8b7d18362dbad3467f61e320ee9...,2025-10-07 01:05:00,30,NO CONTROLS,NO CONTROLS,OTHER,"DARKNESS, LIGHTED ROAD",PARKED MOTOR VEHICLE,NOT DIVIDED,STRAIGHT AND LEVEL,...,0.0,0.0,1.0,1,3,10,41.826667,-87.689679,POINT (-87.689678969045 41.826666608837),60632
2,66c8fb7ca043fb91fa194c4c82acb20b8a54fc3e478deb...,2025-10-07 00:47:00,25,STOP SIGN/FLASHER,UNKNOWN,RAIN,"DARKNESS, LIGHTED ROAD",FIXED OBJECT,T-INTERSECTION,STRAIGHT AND LEVEL,...,0.0,0.0,2.0,0,3,10,41.885533,-87.759074,POINT (-87.759073957098 41.885532532443),60644
3,543b08b85ce5854c761d4def4fcbf0602f55e0cfdd991c...,2025-10-07 00:45:00,25,NO CONTROLS,NO CONTROLS,CLEAR,"DARKNESS, LIGHTED ROAD",PARKED MOTOR VEHICLE,ONE-WAY,STRAIGHT AND LEVEL,...,1.0,0.0,0.0,0,3,10,41.823030,-87.621437,POINT (-87.621437387284 41.823029573152),60653
4,afd384a0563e4639e61ca9d13f3036f91b1fb16268e466...,2025-10-06 23:48:00,35,NO CONTROLS,NO CONTROLS,CLEAR,DARKNESS,SIDESWIPE SAME DIRECTION,NOT DIVIDED,STRAIGHT AND LEVEL,...,0.0,0.0,2.0,23,2,10,41.828208,-87.670489,POINT (-87.670488777376 41.828207872994),60609



Info about df_cleaned after adding zipcode column:
<class 'pandas.core.frame.DataFrame'>
Index: 949110 entries, 0 to 991121
Data columns (total 39 columns):
 #   Column                         Non-Null Count   Dtype         
---  ------                         --------------   -----         
 0   CRASH_RECORD_ID                949110 non-null  object        
 1   CRASH_DATE                     949110 non-null  datetime64[ns]
 2   POSTED_SPEED_LIMIT             949110 non-null  int64         
 3   TRAFFIC_CONTROL_DEVICE         949110 non-null  object        
 4   DEVICE_CONDITION               949110 non-null  object        
 5   WEATHER_CONDITION              949110 non-null  object        
 6   LIGHTING_CONDITION             949110 non-null  object        
 7   FIRST_CRASH_TYPE               949110 non-null  object        
 8   TRAFFICWAY_TYPE                949110 non-null  object        
 9   ALIGNMENT                      949110 non-null  object        
 10  ROADWAY_SURFACE_COND 

In [ ]:
import os
os.chdir('C:/Users/dgdgi/OneDrive/Personal/Class Materials/FSE 570/Data/')
import requests
import pandas as pd
import geopandas as gpd
import numpy as np
from shapely.geometry import Point
from IPython.display import Markdown, display

speed_camera_locations_df = pd.read_csv("Speed_Camera_Locations_20251007.csv")
speed_camera_violations_df = pd.read_csv("Speed_Camera_Violations_20251007.csv")
##red_light_camera_locations_df = pd.read_csv("Red_Light_Camera_Locations_20251007.csv")
## we cleaned this manually to map camera IDs to locations
red_light_camera_locations_df = pd.read_excel("df_redlight_locations (with camera ID).xlsx")
red_light_camera_violations_df = pd.read_csv("Red_Light_Camera_Violations_20251007.csv")

print("--- Initial Null Value Counts ---")
print("\nSpeed Camera Violations Nulls:")
print(speed_camera_violations_df.isnull().sum())

print("\nRed Light Camera Violations Nulls:")
print(red_light_camera_violations_df.isnull().sum())

print("\nSpeed Camera Locations Nulls:")
print(speed_camera_locations_df.isnull().sum())

print("\nRed Light Camera Locations Nulls:")
print(red_light_camera_locations_df.isnull().sum())

C:\Users\dgdgi\AppData\Local\Temp\ipykernel_45432\3828644887.py:11: DtypeWarning: Columns (3) have mixed types. Specify dtype option on import or set low_memory=False.
  speed_camera_violations_df = pd.read_csv("Speed_Camera_Violations_20251007.csv")


--- Initial Null Value Counts ---

Speed Camera Violations Nulls:
ADDRESS               0
CAMERA ID             5
VIOLATION DATE        0
VIOLATIONS            0
X COORDINATE      16169
Y COORDINATE      16169
LATITUDE          16169
LONGITUDE         16169
LOCATION          16169
dtype: int64

Red Light Camera Violations Nulls:
INTERSECTION          0
CAMERA ID           289
ADDRESS               0
VIOLATION DATE        0
VIOLATIONS            0
X COORDINATE      56000
Y COORDINATE      56000
LATITUDE          56000
LONGITUDE         56000
LOCATION          56000
dtype: int64

Speed Camera Locations Nulls:
ID                  0
LOCATION ID         0
ADDRESS             0
FIRST APPROACH      0
SECOND APPROACH    94
GO-LIVE DATE        0
LATITUDE            0
LONGITUDE           0
LOCATION            0
dtype: int64

Red Light Camera Locations Nulls:
INTERSECTION              0
CAMERA ID                 7
GO LIVE DATE              0
LATITUDE                  0
LONGITUDE                 0

In [ ]:
speed_camera_locations_df['ONE DIRECTION BINARY'] = speed_camera_locations_df['SECOND APPROACH'].isna().astype(int)
speed_camera_locations_df.drop(columns=['ID','ADDRESS','FIRST APPROACH','SECOND APPROACH'], inplace=True)
speed_camera_locations_df.rename(columns={'LOCATION ID': 'CAMERA ID'}, inplace=True)
speed_camera_locations_df["CAMERA ID"] = speed_camera_locations_df["CAMERA ID"].astype(str)

speed_camera_violations_df.drop(columns=['ADDRESS','X COORDINATE','Y COORDINATE'], inplace=True)
speed_camera_violations_df["CAMERA ID"] = speed_camera_violations_df["CAMERA ID"].astype(str)
speed_camera_violations_df = speed_camera_violations_df.dropna()

##used to clean raw data, see above import of cleaned manual data
##red_light_camera_locations_df['ONE ORIENTATION BINARY'] = red_light_camera_locations_df['THIRD APPROACH'].isna().astype(int)
##red_light_camera_locations_df.drop(columns=['FIRST APPROACH','SECOND APPROACH','THIRD APPROACH'], inplace=True)

red_light_camera_violations_df.drop(columns=['ADDRESS','X COORDINATE','Y COORDINATE'], inplace=True)
red_light_camera_violations_df = red_light_camera_violations_df.dropna()


for df, cols in [(red_light_camera_violations_df, ['LATITUDE', 'LONGITUDE'])]:
    for col in cols:
        df[col] = df[col].round(3)




In [ ]:
#### cleaning and merging camera locations with violations data
# Convert the 'CAMERA ID' column to string to handle any non-string values
red_light_camera_locations_df['CAMERA ID'] = red_light_camera_locations_df['CAMERA ID'].astype(str)

# Split the 'CAMERA ID' column by the '/' delimiter.
# This turns each cell into a list of one or more IDs.
red_light_camera_locations_df['CAMERA ID'] = red_light_camera_locations_df['CAMERA ID'].str.split('/')

# Use the explode() function to create a new row for each ID in the lists
red_light_camera_locations_df_normalized = red_light_camera_locations_df.explode('CAMERA ID')

# Reset the index for a cleaner DataFrame
red_light_camera_locations_df_normalized.reset_index(drop=True, inplace=True)

# Display the first few rows of the new, transformed data
print(red_light_camera_locations_df_normalized.head())

unique_camera_ids_violations = red_light_camera_violations_df['CAMERA ID'].unique()
unique_camera_ids_locations = red_light_camera_locations_df_normalized['CAMERA ID'].unique()

# Convert 'CAMERA ID' in violations DataFrame to float, then to integer, then back to string to remove .0
red_light_camera_violations_df['CAMERA ID'] = pd.to_numeric(red_light_camera_violations_df['CAMERA ID'], errors='coerce').astype(float).astype(pd.Int64Dtype()).astype(str)

# Merge the dataframes on the 'CAMERA ID' column
merged_red_light_df = pd.merge(red_light_camera_locations_df_normalized, red_light_camera_violations_df, on='CAMERA ID', how='inner')
print(f"Number of rows in the merged_red_light_df: {len(merged_red_light_df)}")

unique_speed_camera_ids_locations = speed_camera_locations_df['CAMERA ID'].unique()
unique_speed_camera_ids_violations = speed_camera_violations_df['CAMERA ID'].unique()

# Check if any cell in 'CAMERA ID' contains a delimiter (like '/') indicating multiple IDs
# Based on the previous examination, we don't expect this, but we will verify.
# We will check for the presence of the '/' character as it was used in the red light data.
has_multiple_ids = speed_camera_locations_df['CAMERA ID'].astype(str).str.contains('/').any()

if has_multiple_ids:
    print("Multiple camera IDs found in speed_camera_locations_df. Normalizing...")
    # Normalize the 'CAMERA ID' column if multiple IDs exist
    speed_camera_locations_df['CAMERA ID'] = speed_camera_locations_df['CAMERA ID'].astype(str).str.split('/')
    speed_camera_locations_df_normalized = speed_camera_locations_df.explode('CAMERA ID')
    speed_camera_locations_df_normalized.reset_index(drop=True, inplace=True)
    print("Normalization complete. Displaying head of normalized dataframe:")
    display(speed_camera_locations_df_normalized.head())
else:
    print("No multiple camera IDs found in speed_camera_locations_df. No normalization needed.")
    # If no normalization is needed, just keep the original dataframe for the next steps
    speed_camera_locations_df_normalized = speed_camera_locations_df.copy()
    display(speed_camera_locations_df_normalized.head())


# Clean 'CAMERA ID' in speed_camera_locations_df_normalized (which is a copy if no explode was needed)
# Remove any leading/trailing whitespace from 'CAMERA ID'
speed_camera_locations_df_normalized['CAMERA ID'] = speed_camera_locations_df_normalized['CAMERA ID'].astype(str).str.strip()

# Clean 'CAMERA ID' in speed_camera_violations_df
# Fill NaN values with a placeholder or drop them, then remove any leading/trailing whitespace
# For merging, it's better to drop NaNs or convert them to a non-matching string if necessary.
# Given the small number of NaNs, dropping is a reasonable approach here.
speed_camera_violations_df.dropna(subset=['CAMERA ID'], inplace=True)
speed_camera_violations_df['CAMERA ID'] = speed_camera_violations_df['CAMERA ID'].astype(str).str.strip()

# Ensure both 'CAMERA ID' columns are of the same data type (string) before merging
speed_camera_locations_df_normalized['CAMERA ID'] = speed_camera_locations_df_normalized['CAMERA ID'].astype(str)
speed_camera_violations_df['CAMERA ID'] = speed_camera_violations_df['CAMERA ID'].astype(str)

# Merge the dataframes on the cleaned 'CAMERA ID' column
merged_speed_light_df = pd.merge(speed_camera_locations_df_normalized, speed_camera_violations_df, on='CAMERA ID', how='inner')

# Display the first few rows of the merged DataFrame
display(merged_speed_light_df.head())

print(f"Number of rows in the merged_speed_light_df: {len(merged_speed_light_df)}")

       INTERSECTION CAMERA ID GO LIVE DATE  LATITUDE  LONGITUDE  \
0   Cicero-Peterson      1202   2008-08-25    41.990    -87.748   
1   Cicero-Peterson      1204   2008-08-25    41.990    -87.748   
2  Western-Peterson      1011   2004-02-25    41.990    -87.690   
3  Western-Peterson      1014   2004-02-25    41.990    -87.690   
4    Harlem-Belmont      1391   2007-06-17    41.938    -87.807   

                LOCATION  ONE ORIENTATION BINARY  
0  (41.98989, -87.74832)                       1  
1  (41.98989, -87.74832)                       1  
2    (41.9905, -87.6897)                       1  
3    (41.9905, -87.6897)                       1  
4  (41.93799, -87.80674)                       1  
Number of rows in the merged_red_light_df: 971553
No multiple camera IDs found in speed_camera_locations_df. No normalization needed.


,CAMERA ID,GO-LIVE DATE,LATITUDE,LONGITUDE,LOCATION,ONE DIRECTION BINARY
0,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0
1,CHI039,12/21/2013,41.9236,-87.7825,"(41.9236, -87.7825)",1
2,CHI040,12/21/2013,41.9238,-87.7826,"(41.9238, -87.7826)",1
3,CHI041,12/12/2013,41.9239,-87.7639,"(41.9239, -87.7639)",1
4,CHI042,12/12/2013,41.9241,-87.7630,"(41.9241, -87.763)",1


,CAMERA ID,GO-LIVE DATE,LATITUDE_x,LONGITUDE_x,LOCATION_x,ONE DIRECTION BINARY,VIOLATION DATE,VIOLATIONS,LATITUDE_y,LONGITUDE_y,LOCATION_y
0,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,09/02/2025,11,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)"
1,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,09/01/2025,25,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)"
2,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/31/2025,28,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)"
3,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/30/2025,26,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)"
4,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/29/2025,16,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)"


Number of rows in the merged_speed_light_df: 387913


In [ ]:
## now assign zip codes to cameras
#!pip install geopy
#!pip install geopandas
from geopy.geocoders import Nominatim
import time

geolocator = Nominatim(user_agent="traffic_analysis_app")

def get_zipcode(latitude, longitude):
    """
    Performs reverse geocoding to get the zipcode for given latitude and longitude.

    Args:
        latitude (float): The latitude of the location.
        longitude (float): The longitude of the location.

    Returns:
        str: The zipcode if found, otherwise 'Unknown'.
    """
    try:
        location = geolocator.reverse(f"{latitude}, {longitude}", exactly_one=True)
        if location and 'address' in location.raw:
            address = location.raw['address']
            zipcode = address.get('postcode') or address.get('postalcode')
            if zipcode:
                return zipcode
    except Exception as e:
        print(f"Error geocoding {latitude}, {longitude}: {e}")
    return 'Unknown'

# Test the function with a sample coordinate from the merged_red_light_df
sample_lat = merged_red_light_df['LATITUDE_x'].iloc[0]
sample_lon = merged_red_light_df['LONGITUDE_x'].iloc[0]
test_zipcode = get_zipcode(sample_lat, sample_lon)
print(f"Test zipcode for ({sample_lat}, {sample_lon}): {test_zipcode}")

# Add a small delay to avoid hitting the geocoding service too quickly during testing
time.sleep(1)

# Test the function with a sample coordinate from the merged_speed_light_df
sample_lat_speed = merged_speed_light_df['LATITUDE_x'].iloc[0]
sample_lon_speed = merged_speed_light_df['LONGITUDE_x'].iloc[0]
test_zipcode_speed = get_zipcode(sample_lat_speed, sample_lon_speed)
print(f"Test zipcode for ({sample_lat_speed}, {sample_lon_speed}): {test_zipcode_speed}")



Test zipcode for (41.99, -87.748): 60646
Test zipcode for (41.7644, -87.7097): 60629


In [ ]:
# Apply the get_zipcode function to the red_light_camera_locations_df_normalized
# Introduce a small delay between requests

# Create a list of zipcodes by applying the function row-wise
zipcodes = []
for index, row in red_light_camera_locations_df_normalized.iterrows():
    zipcode = get_zipcode(row['LATITUDE'], row['LONGITUDE'])
    zipcodes.append(zipcode)
    print(f"working...")
    time.sleep(1) # Add a 1-second delay

# Assign the list of zipcodes to a new column
red_light_camera_locations_df_normalized['Zipcode'] = zipcodes

# Display the head of the DataFrame with the new 'Zipcode' column
display(red_light_camera_locations_df_normalized.head())

working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...
working...

,INTERSECTION,CAMERA ID,GO LIVE DATE,LATITUDE,LONGITUDE,LOCATION,ONE ORIENTATION BINARY,Zipcode
0,Cicero-Peterson,1202,2008-08-25,41.990,-87.748,"(41.98989, -87.74832)",1,60646
1,Cicero-Peterson,1204,2008-08-25,41.990,-87.748,"(41.98989, -87.74832)",1,60646
2,Western-Peterson,1011,2004-02-25,41.990,-87.690,"(41.9905, -87.6897)",1,60659
3,Western-Peterson,1014,2004-02-25,41.990,-87.690,"(41.9905, -87.6897)",1,60659
4,Harlem-Belmont,1391,2007-06-17,41.938,-87.807,"(41.93799, -87.80674)",1,60634


In [ ]:
# Merge the 'Zipcode' column from red_light_camera_locations_df_normalized onto merged_red_light_df
# We'll use an inner merge to keep only the rows with matching CAMERA IDs
merged_red_light_df = pd.merge(merged_red_light_df, red_light_camera_locations_df_normalized[['CAMERA ID', 'Zipcode']], on='CAMERA ID', how='inner')

# Display the first few rows of the updated merged_red_light_df with the Zipcode column
display(merged_red_light_df.head())

,INTERSECTION_x,CAMERA ID,GO LIVE DATE,LATITUDE_x,LONGITUDE_x,LOCATION_x,ONE ORIENTATION BINARY,INTERSECTION_y,VIOLATION DATE,VIOLATIONS,LATITUDE_y,LONGITUDE_y,LOCATION_y,Zipcode
0,Cicero-Peterson,1202,2008-08-25,41.99,-87.748,"(41.98989, -87.74832)",1,CICERO AND PETERSON,09/13/2025,2,41.99,-87.748,"(41.98997391514614, -87.74847302426933)",60646
1,Cicero-Peterson,1202,2008-08-25,41.99,-87.748,"(41.98989, -87.74832)",1,CICERO AND PETERSON,09/11/2025,2,41.99,-87.748,"(41.98997391514614, -87.74847302426933)",60646
2,Cicero-Peterson,1202,2008-08-25,41.99,-87.748,"(41.98989, -87.74832)",1,CICERO AND PETERSON,09/10/2025,2,41.99,-87.748,"(41.98997391514614, -87.74847302426933)",60646
3,Cicero-Peterson,1202,2008-08-25,41.99,-87.748,"(41.98989, -87.74832)",1,CICERO AND PETERSON,09/08/2025,2,41.99,-87.748,"(41.98997391514614, -87.74847302426933)",60646
4,Cicero-Peterson,1202,2008-08-25,41.99,-87.748,"(41.98989, -87.74832)",1,CICERO AND PETERSON,09/06/2025,1,41.99,-87.748,"(41.98997391514614, -87.74847302426933)",60646


In [ ]:
# Apply the get_zipcode function to the speed_camera_locations_df_normalized
# Introduce a small delay between requests

zipcodes_speed = []
for index, row in speed_camera_locations_df_normalized.iterrows():
    zipcode = get_zipcode(row['LATITUDE'], row['LONGITUDE'])
    zipcodes_speed.append(zipcode)
    print(f"Geocoding speed camera location {index + 1}/{len(speed_camera_locations_df_normalized)}...")
    time.sleep(1) # Add a 1-second delay

# Assign the list of zipcodes to a new column
speed_camera_locations_df_normalized['Zipcode'] = zipcodes_speed

# Display the head of the DataFrame with the new 'Zipcode' column
display(speed_camera_locations_df_normalized.head())

Geocoding speed camera location 1/209...
Geocoding speed camera location 2/209...
Geocoding speed camera location 3/209...
Geocoding speed camera location 4/209...
Geocoding speed camera location 5/209...
Geocoding speed camera location 6/209...
Geocoding speed camera location 7/209...
Geocoding speed camera location 8/209...
Geocoding speed camera location 9/209...
Geocoding speed camera location 10/209...
Geocoding speed camera location 11/209...
Geocoding speed camera location 12/209...
Geocoding speed camera location 13/209...
Geocoding speed camera location 14/209...
Geocoding speed camera location 15/209...
Geocoding speed camera location 16/209...
Geocoding speed camera location 17/209...
Geocoding speed camera location 18/209...
Geocoding speed camera location 19/209...
Geocoding speed camera location 20/209...
Geocoding speed camera location 21/209...
Geocoding speed camera location 22/209...
Geocoding speed camera location 23/209...
Geocoding speed camera location 24/209...
G

,CAMERA ID,GO-LIVE DATE,LATITUDE,LONGITUDE,LOCATION,ONE DIRECTION BINARY,Zipcode
0,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,60629
1,CHI039,12/21/2013,41.9236,-87.7825,"(41.9236, -87.7825)",1,60707
2,CHI040,12/21/2013,41.9238,-87.7826,"(41.9238, -87.7826)",1,60707
3,CHI041,12/12/2013,41.9239,-87.7639,"(41.9239, -87.7639)",1,60639
4,CHI042,12/12/2013,41.9241,-87.7630,"(41.9241, -87.763)",1,60639


In [ ]:
# Merge the 'Zipcode' column from speed_camera_locations_df_normalized onto merged_speed_light_df
# We'll use an inner merge to keep only the rows with matching CAMERA IDs
merged_speed_light_df = pd.merge(merged_speed_light_df, speed_camera_locations_df_normalized[['CAMERA ID', 'Zipcode']], on='CAMERA ID', how='inner')

# Display the first few rows of the updated merged_speed_light_df with the Zipcode column
display(merged_speed_light_df.head())



,CAMERA ID,GO-LIVE DATE,LATITUDE_x,LONGITUDE_x,LOCATION_x,ONE DIRECTION BINARY,VIOLATION DATE,VIOLATIONS,LATITUDE_y,LONGITUDE_y,LOCATION_y,Zipcode
0,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,09/02/2025,11,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)",60629
1,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,09/01/2025,25,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)",60629
2,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/31/2025,28,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)",60629
3,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/30/2025,26,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)",60629
4,CHI015,09/06/2013,41.7644,-87.7097,"(41.7644, -87.7097)",0,08/29/2025,16,41.764391,-87.709728,"(41.76439095689881, -87.70972841983624)",60629


In [ ]:
# Select the desired columns for merged_red_light_df
merged_red_light_df = merged_red_light_df[['INTERSECTION_x', 'CAMERA ID', 'GO LIVE DATE', 'ONE ORIENTATION BINARY', 'VIOLATION DATE', 'VIOLATIONS', 'LATITUDE_x', 'LONGITUDE_x', 'Zipcode']]

# Rename columns for clarity
merged_red_light_df.rename(columns={'INTERSECTION_x': 'INTERSECTION',
                                     'GO LIVE DATE': 'GO-LIVE DATE',
                                     'LATITUDE_x': 'LATITUDE',
                                     'LONGITUDE_x': 'LONGITUDE'}, inplace=True)

# Select the desired columns for merged_speed_light_df
merged_speed_light_df = merged_speed_light_df[['CAMERA ID', 'GO-LIVE DATE', 'ONE DIRECTION BINARY', 'VIOLATION DATE', 'VIOLATIONS', 'LATITUDE_x', 'LONGITUDE_x', 'Zipcode']]

# Rename columns for clarity
merged_speed_light_df.rename(columns={'LATITUDE_x': 'LATITUDE',
                                     'LONGITUDE_x': 'LONGITUDE'}, inplace=True)

print(f"Number of rows in merged_red_light_df: {len(merged_red_light_df)}")
print(f"Number of rows in merged_speed_light_df: {len(merged_speed_light_df)}")

# Count unique camera IDs in merged_red_light_df
unique_red_light_cameras = merged_red_light_df['CAMERA ID'].nunique()
print(f"Number of unique red light camera IDs in merged_red_light_df: {unique_red_light_cameras}")

# Count unique camera IDs in merged_speed_light_df
unique_speed_light_cameras = merged_speed_light_df['CAMERA ID'].nunique()
print(f"Number of unique speed camera IDs in merged_speed_light_df: {unique_speed_light_cameras}")

Number of rows in merged_red_light_df: 986981
Number of rows in merged_speed_light_df: 387913
Number of unique red light camera IDs in merged_red_light_df: 276
Number of unique speed camera IDs in merged_speed_light_df: 194


In [ ]:
crashes_url = "https://data.cityofchicago.org/resource/85ca-t3if.csv?$limit=2000000"
vehicles_url = "https://data.cityofchicago.org/resource/68nd-jvt3.csv?$limit=2000000"

##crashes_df = pd.read_csv(crashes_url)
crashes_df = df_crashes_cleaned.copy()
vehicles_df = pd.read_csv(vehicles_url)

print(crashes_df.shape)
print(vehicles_df.shape)


C:\Users\dgdgi\AppData\Local\Temp\ipykernel_23820\1578432113.py:6: DtypeWarning: Columns (18,20,39,40,41,43,47,48,49,52,54,57,58,60,70) have mixed types. Specify dtype option on import or set low_memory=False.
  vehicles_df = pd.read_csv(vehicles_url)


(949110, 38)
(2000000, 71)



## 🚦 Chicago Traffic Crash Data Dictionary (Crash-Level)

| **Column Name** | **Description** |
|------------------|-----------------|
| `crash_record_id` | Unique identifier for each crash event. |
| `crash_date_est_i` | Indicates if crash date/time is an estimate. |
| `crash_date` | Exact date and time of the crash. |
| `posted_speed_limit` | Posted speed limit at the crash location. |
| `traffic_control_device` | Type of traffic control (e.g., stop sign, signal). |
| `device_condition` | Operational condition of the traffic device. |
| `weather_condition` | Weather at the time of the crash. |
| `lighting_condition` | Lighting conditions (e.g., daylight, dark). |
| `first_crash_type` | Type of first event in the crash (e.g., rear-end, sideswipe). |
| `trafficway_type` | Roadway configuration (e.g., divided, undivided). |
| `lane_cnt` | Number of lanes in the roadway. |
| `alignment` | Road alignment (e.g., straight, curve). |
| `roadway_surface_cond` | Surface condition (e.g., dry, wet, icy). |
| `road_defect` | Any physical defects in the road. |
| `report_type` | Type of police crash report. |
| `crash_type` | Severity/type (e.g., injury, property damage). |
| `intersection_related_i` | Indicates if the crash occurred near an intersection. |
| `private_property_i` | Indicates if crash occurred on private property. |
| `hit_and_run_i` | Indicates if a hit-and-run was involved. |
| `damage` | Extent of damage (e.g., over/under $1,500). |
| `date_police_notified` | Date police were notified of the crash. |
| `prim_contributory_cause` | Primary cause of the crash. |
| `sec_contributory_cause` | Secondary contributing factor. |
| `street_no` | Street number where crash occurred. |
| `street_direction` | Direction of street (e.g., N, S, E, W). |
| `street_name` | Name of street where crash occurred. |
| `beat_of_occurrence` | Police beat (patrol area) of crash. |
| `photos_taken_i` | Indicates if police took photos at the scene. |
| `statements_taken_i` | Indicates if witness statements were taken. |
| `dooring_i` | Indicates if crash involved a vehicle door opening into traffic. |
| `work_zone_i` | Indicates if crash occurred in a work zone. |
| `work_zone_type` | Type of work zone (e.g., lane closure). |
| `workers_present_i` | Indicates if workers were present in the work zone. |
| `num_units` | Number of vehicles/units involved in the crash. |
| `most_severe_injury` | Highest level of injury severity in the crash. |
| `injuries_total` | Total number of injuries. |
| `injuries_fatal` | Number of fatalities. |
| `injuries_incapacitating` | Number of incapacitating injuries. |
| `injuries_non_incapacitating` | Number of non-incapacitating injuries. |
| `injuries_reported_not_evident` | Number of reported but not visible injuries. |
| `injuries_no_indication` | Number of people with no apparent injury. |
| `injuries_unknown` | Number of people with unknown injury status. |
| `crash_hour` | Hour of the day when the crash occurred. |
| `crash_day_of_week` | Day of the week of the crash. |
| `crash_month` | Month when the crash occurred. |
| `latitude` | Latitude of the crash location. |
| `longitude` | Longitude of the crash location. |
| `location` | Combined geographic coordinates (Point geometry). |
"""))

## 🚗 Chicago Traffic Crash Vehicle Data Dictionary (Vehicle-Level)

| **Column Name** | **Description** |
|------------------|-----------------|
| `crash_unit_id` | Unique identifier for each unit involved in a crash. |
| `crash_record_id` | Unique identifier for the crash event. |
| `crash_date` | Date and time of the crash. |
| `unit_no` | Sequential number assigned to each vehicle/unit in the crash. |
| `unit_type` | Type of unit (vehicle, pedestrian, etc.). |
| `num_passengers` | Number of passengers in the vehicle. |
| `vehicle_id` | Vehicle identification number. |
| `make` | Manufacturer of the vehicle. |
| `model` | Model of the vehicle. |
| `vehicle_year` | Model year of the vehicle. |
| `vehicle_type` | Type/category of vehicle (e.g., sedan, truck). |
| `vehicle_use` | Purpose of use (personal, commercial, etc.). |
| `travel_direction` | Direction the vehicle was traveling. |
| `maneuver` | Vehicle maneuver at the time of crash. |
| `towed_i` | Whether the vehicle was towed. |
| `fire_i` | Whether the vehicle caught fire. |
| `occupant_cnt` | Number of occupants in the vehicle. |
| `exceed_speed_limit_i` | Whether speeding occurred. |
| `first_contact_point` | Point of initial impact on the vehicle. |
| `cmv_id` | Commercial motor vehicle ID. |
| `usdot_no` | USDOT number for carriers. |
| `carrier_name` | Name of carrier company. |
| `hazmat_present_i` | Whether hazardous materials were present. |
| `hazmat_name` | Name of hazardous material. |
| `hazmat_class` | Hazardous material class number. |
"""))


In [ ]:
vehicles_df.columns = vehicles_df.columns.str.lower()
crashes_df.columns = crashes_df.columns.str.lower()


In [ ]:
import geopandas as gpd
from shapely.geometry import Point


####merged df for later use using vehicle info- GDF still made on crashes to represent aggregates accurately
#merged_df = pd.merge(crashes_df, vehicles_df, on="crash_record_id", how="left")

#print("\n=== Merged Dataset Preview ===")
#display(merged_df.head(3))

#print(f"\n✅ Merged dataset shape: {merged_df.shape}")
# Convert crash data to GeoDataFrame
gdf = gpd.GeoDataFrame(
    crashes_df, geometry=gpd.points_from_xy(crashes_df.longitude, crashes_df.latitude), crs="EPSG:4326"
)

# Load Chicago ZIP code boundaries
zip_gdf = gpd.read_file("https://data.cityofchicago.org/resource/unjd-c2ca.geojson")  # official ZIP shapefile

# Spatial join to get ZIP codes
gdf_with_zip = gpd.sjoin(gdf, zip_gdf, how="left", predicate="within")

# The ZIP code column is usually named 'zip' or 'zip_code'
gdf_with_zip.head()
gdf_with_zip = gdf_with_zip.rename(columns={"zip": "zip_code"})

zip_crash_counts = (
    gdf_with_zip.groupby("zip_code")
    .size()
    .reset_index(name="num_crashes")
    .sort_values(by="num_crashes", ascending=False)
)

print("✅ Number of crashes per ZIP code:")
display(zip_crash_counts.head(100))

# --- Install Folium if not already installed ---
!pip install folium geopandas

import folium
import geopandas as gpd

# --- Reload Chicago ZIP code boundaries ---
zip_url = "https://data.cityofchicago.org/resource/unjd-c2ca.geojson"
zip_gdf = gpd.read_file(zip_url)
zip_gdf = zip_gdf.rename(columns={'zip': 'zip_code'})

# --- Merge crash counts with ZIP geometry ---
zip_map = zip_gdf.merge(zip_crash_counts, on="zip_code", how="left")
zip_map["num_crashes"] = zip_map["num_crashes"].fillna(0)

# --- Create Folium Map centered on Chicago ---
m = folium.Map(location=[41.8781, -87.6298], zoom_start=10, tiles="cartodbpositron")

# --- Add choropleth layer (ZIPs colored by crash density) ---
folium.Choropleth(
    geo_data=zip_map,
    data=zip_map,
    columns=["zip_code", "num_crashes"],
    key_on="feature.properties.zip_code",
    fill_color="YlOrRd",
    fill_opacity=0.7,
    line_opacity=0.4,
    legend_name="Number of Crashes (2020–Present)",
).add_to(m)

# --- Add hover tooltip to show ZIP and crash count ---
folium.GeoJsonTooltip(
    fields=["zip_code", "num_crashes"],
    aliases=["ZIP Code:", "Crashes:"],
    localize=True
).add_to(folium.GeoJson(zip_map).add_to(m))

# --- Display map ---
m

✅ Number of crashes per ZIP code:


,zip_code,num_crashes
27,60629,35589
30,60632,32661
19,60620,32266
18,60619,30987
22,60623,27811
41,60644,27090
36,60639,26910
7,60608,26838
17,60618,26828
8,60609,24613


In [ ]:
# --- Install dependencies if needed ---
import folium
import geopandas as gpd

# --- Filter to ZIP 60614 only ---
zip_target = "60614"
crashes_60614 = gdf_with_zip[gdf_with_zip["zip_code"] == zip_target]

print(f"✅ Found {len(crashes_60614)} crashes in ZIP {zip_target}")

# --- Get average lat/lon to center the map ---
center_lat = crashes_60614["latitude"].mean()
center_lon = crashes_60614["longitude"].mean()

# --- Create Folium map centered on 60614 ---
m = folium.Map(location=[center_lat, center_lon], zoom_start=13, tiles="cartodbpositron")

# --- Add each crash as a point marker (CircleMarker for performance) ---
for _, row in crashes_60614.iterrows():
    folium.CircleMarker(
        location=[row["latitude"], row["longitude"]],
        radius=2,
        color="red",
        fill=True,
        fill_opacity=0.5
    ).add_to(m)

# --- Add a title marker ---
folium.map.Marker(
    [center_lat, center_lon],
    icon=folium.DivIcon(
        html=f"""<div style="font-size: 16pt; color: black"><b>Crashes in ZIP {zip_target}</b></div>"""
    )
).add_to(m)

# --- Display the map ---
m


✅ Found 20224 crashes in ZIP 60614


In [ ]:
zip_summary = (
    gdf_with_zip.groupby("zip_code")
    .agg(
        num_crashes=("crash_record_id", "count"),
        total_injuries=("injuries_total", "sum"),
        fatal_crashes=("injuries_fatal", "sum"),
        #avg_vehicle_age=("vehicle_year", lambda x: 2025 - x.dropna().astype(int).mean()),
        hit_and_run_rate=("hit_and_run_i", lambda x: (x == "Y").mean()),
        intersection_rate=("intersection_related_i", lambda x: (x == "Y").mean())
    )
    .reset_index()
)

display(zip_summary.head())

zip_codes = sorted(gdf_with_zip['zip_code'].dropna().unique())
zip_codes

,zip_code,num_crashes,total_injuries,fatal_crashes,hit_and_run_rate,intersection_rate
0,60601,7936,1266.0,5.0,0.0,0.0
1,60602,3556,441.0,0.0,0.0,0.0
2,60603,3948,578.0,2.0,0.0,0.0
3,60604,2973,521.0,1.0,0.0,0.0
4,60605,14557,2249.0,14.0,0.0,0.0


['60601',
 '60602',
 '60603',
 '60604',
 '60605',
 '60606',
 '60607',
 '60608',
 '60609',
 '60610',
 '60611',
 '60612',
 '60613',
 '60614',
 '60615',
 '60616',
 '60617',
 '60618',
 '60619',
 '60620',
 '60621',
 '60622',
 '60623',
 '60624',
 '60625',
 '60626',
 '60628',
 '60629',
 '60630',
 '60631',
 '60632',
 '60633',
 '60634',
 '60636',
 '60637',
 '60638',
 '60639',
 '60640',
 '60641',
 '60642',
 '60643',
 '60644',
 '60645',
 '60646',
 '60647',
 '60649',
 '60651',
 '60652',
 '60653',
 '60654',
 '60655',
 '60656',
 '60657',
 '60659',
 '60660',
 '60661',
 '60666',
 '60707',
 '60827']

In [ ]:
### PEOPLE DATA

input_file = "Traffic_Crashes_-_People_20251007.csv"

print("Loading dataset...")
df = pd.read_csv(input_file, low_memory=False)
initial_rows = df.shape[0]
print(f"Initial dataset shape: {df.shape}")

# Convert datatypes for consistency
df["CRASH_DATE"] = pd.to_datetime(df["CRASH_DATE"], errors="coerce")
df["AGE"] = pd.to_numeric(df["AGE"], errors="coerce", downcast="integer")
df["SEX"] = df["SEX"].astype("category")
df["PERSON_TYPE"] = df["PERSON_TYPE"].astype("category")
df["INJURY_CLASSIFICATION"] = df["INJURY_CLASSIFICATION"].astype("category")

# Remove duplicates
before_dupes = df.shape[0]
df = df.drop_duplicates()
print(f"Removed {before_dupes - df.shape[0]} duplicate rows")

# Clean AGE column and handle unrealistic or missing values
df.loc[(df["AGE"] < 10) | (df["AGE"] > 100), "AGE"] = None
median_age = df["AGE"].median()
df["AGE"].fillna(median_age, inplace=True)
print(f"Age column cleaned. Median age used for fill: {median_age:.0f}")
print(f"Age stats after cleaning - Min: {df['AGE'].min()}, Max: {df['AGE'].max()}, Mean: {df['AGE'].mean():.2f}")

# Normalize gender values and remove invalid entries
df["SEX"] = df["SEX"].astype(str).str.strip().str.upper()
df["SEX"].replace({"MALE": "M", "FEMALE": "F", "UNKNOWN": None, "X": None}, inplace=True)
before_sex = df.shape[0]
df = df[df["SEX"].isin(["M", "F"])]
print(f"Removed {before_sex - df.shape[0]} rows with invalid gender values")

# Keep valid 5-digit ZIP codes
df["ZIPCODE"] = df["ZIPCODE"].astype(str).str.extract(r"(\d{5})")[0]

# Ensure valid CRASH_DATE values
before_date = df.shape[0]
df["CRASH_DATE"] = pd.to_datetime(df["CRASH_DATE"], errors="coerce")
df = df.dropna(subset=["CRASH_DATE"])
print(f"Removed {before_date - df.shape[0]} rows with invalid crash dates")
df.drop(columns=["VEHICLE_ID"], inplace=True)

# Clean INJURY_CLASSIFICATION column
df["INJURY_CLASSIFICATION"] = df["INJURY_CLASSIFICATION"].astype(str).str.strip().str.upper()
before_injury = df.shape[0]
df = df[df["INJURY_CLASSIFICATION"].notna()]
print(f"Removed {before_injury - df.shape[0]} rows with missing injury classification")

# Define Chicago ZIP codes and filter dataset
chicago_zips = [
    '60632', '60620', '60618', '60629', '60623', '60639', '60608', '60619', '60612', '60644',
    '60624', '60616', '60647', '60641', '60614', '60617', '60643', '60651', '60609', '60634',
    '60628', '60607', '60611', '60637', '60625', '60630', '60621', '60638', '60640', '60657',
    '60622', '60605', '60654', '60636', '60649', '60660', '60626', '60659', '60615', '60645',
    '60642', '60652', '60610', '60613', '60653', '60646', '60655', '60601', '60707', '60631',
    '60661', '60656', '60606', '60602', '60633', '60666', '60603', '60604', '60827'
]
before_zip = df.shape[0]
df['LOCAL'] = df['ZIPCODE'].isin(chicago_zips).astype(int)
df.drop(columns="ZIPCODE", inplace=True)

# Summary of final dataset
final_rows = df.shape[0]
print("\nFinal dataset summary:")
print(f"Initial records: {initial_rows}")
print(f"Final records after cleaning and filtering: {final_rows}")
print(f"Total records removed: {initial_rows - final_rows}")
print(f"Final shape: {df.shape}")
print("\nMissing values per column:\n", df.isna().sum())
print("\nUnique injury classifications:")
print(df["INJURY_CLASSIFICATION"].value_counts())
# # Save the final cleaned dataset
# output_path = "/content/drive/MyDrive/df_people.csv"
# df.to_csv(output_path, index=False)
# print(f"\nSaved cleaned and filtered dataset to: {output_path}")



Loading dataset...
Initial dataset shape: (2176450, 9)
Removed 0 duplicate rows
Age column cleaned. Median age used for fill: 36
Age stats after cleaning - Min: 10.0, Max: 100.0, Mean: 38.26


C:\Users\dgdgi\AppData\Local\Temp\ipykernel_23820\1261687414.py:25: FutureWarning: A value is trying to be set on a copy of a DataFrame or Series through chained assignment using an inplace method.
The behavior will change in pandas 3.0. This inplace method will never work because the intermediate object on which we are setting values always behaves as a copy.

For example, when doing 'df[col].method(value, inplace=True)', try using 'df.method({col: value}, inplace=True)' or df[col] = df[col].method(value) instead, to perform the operation inplace on the original object.


  df["AGE"].fillna(median_age, inplace=True)
C:\Users\dgdgi\AppData\Local\Temp\ipykernel_23820\1261687414.py:31: FutureWarning: A value is trying to be set on a copy of a DataFrame or Series through chained assignment using an inplace method.
The behavior will change in pandas 3.0. This inplace method will never work because the intermediate object on which we are setting values always behaves as a copy.

For example

Removed 234832 rows with invalid gender values
Removed 0 rows with invalid crash dates
Removed 0 rows with missing injury classification

Final dataset summary:
Initial records: 2176450
Final records after cleaning and filtering: 1941618
Total records removed: 234832
Final shape: (1941618, 8)

Missing values per column:
 PERSON_ID                0
PERSON_TYPE              0
CRASH_RECORD_ID          0
CRASH_DATE               0
SEX                      0
AGE                      0
INJURY_CLASSIFICATION    0
LOCAL                    0
dtype: int64

Unique injury classifications:
INJURY_CLASSIFICATION
NO INDICATION OF INJURY     1749064
NONINCAPACITATING INJURY     107084
REPORTED, NOT EVIDENT         65342
INCAPACITATING INJURY         18887
FATAL                          1123
NAN                             118
Name: count, dtype: int64


In [ ]:
df_people = df.copy()

In [ ]:
#os.chdir('/content/drive/MyDrive/FSE 570/Clean Data')
df_census.to_csv("df_census.csv", index=False)
df_people.to_csv("df_people.csv", index=False)
df_crashes_cleaned.to_csv("df_crashes.csv", index=False)
vehicles_df.to_csv("df_vehicles.csv", index=False)
merged_red_light_df.to_csv("df_redlights", index=False)
merged_speed_light_df.to_csv("df_speeding", index=False)

#not needed anymore since merged and cleaned above
#speed_camera_locations_df.to_csv("df_speed_locations.csv", index=False)
#speed_camera_violations_df.to_csv("df_speed_violations.csv", index=False)
#red_light_camera_locations_df.to_csv("df_redlight_locations.csv", index=False)
#red_light_camera_violations_df.to_csv("df_redlight_violations.csv", index=False)

print("DataFrames saved as CSV files.")


DataFrames saved as CSV files.
